# Instrument Recognition from Synthetic Data

## Overview

Instrument recognition in polyphonic music is a fundamental task in Music Information Retrieval (MIR). However, training robust models typically requires large datasets with strong labels, which are difficult and expensive to acquire for real-world audio. In this project, we explore whether a multi-instrument classifier trained entirely on synthetic music (Slakh) can generalize to real-world polyphonic recordings (OpenMIC-2018). Instead of training deep networks from scratch, we utilize frozen pre-trained audio foundation models and train shallow classifiers on their extracted features. This approach allows us to isolate the quality of the learned representations and test if they survive a significant synthetic-to-real domain shift. Additionally, we briefly explore whether simple audio augmentations, like applying reverb and other effects, can help bridge the domain gap by improving the acoustic realism of our synthetic training data.

In [1]:
from pathlib import Path
import sys

REPO_DIR = Path.cwd().resolve()
if not (REPO_DIR / "training_base").exists() and (REPO_DIR.parent / "training_base").exists():
    REPO_DIR = REPO_DIR.parent.resolve()

if not (REPO_DIR / "training_base").exists():
    raise FileNotFoundError(
        f"Could not find training_base under {REPO_DIR}. Open this notebook from the repo root or the notebooks/ directory."
    )

repo_str = str(REPO_DIR)
if repo_str not in sys.path:
    sys.path.insert(0, repo_str)

print(f"Using repository: {REPO_DIR}")

Using repository: /home/mg8253/workspace/mir/mir-final-project-instrument-classification


In [2]:
import pandas as pd
from IPython.display import Audio, Markdown, display

from training_base.inference_utils import (
    build_prediction_table_rows,
    list_audio_samples,
    load_model_bundle,
    load_sample_metadata,
    predict_file,
)

/ext3/miniforge3/envs/mir-inst/lib/python3.10/site-packages/tqdm/auto.py:21: TqdmWarning: IProgress not found. Please update jupyter and ipywidgets. See https://ipywidgets.readthedocs.io/en/stable/user_install.html
  from .autonotebook import tqdm as notebook_tqdm


## Encoder Models

For our experiment, we tested three encoders to retrieve the audio embeddings for our classifier. Their details are described below:

### Convolutional Neural Network (CNN) operating on Mel-spectrograms
For our baseline model, we extracted the mel spectrograms of our audio samples and fed them to a convolutional neural network model. Mel spectrograms map frequencies present in our audio samples across time, where the frequencies are logarithmically spaced to better reflect how humans hear. The convolutional neural network slides along the spectrograms with a shared set of weights to learn the features of the audio.

### CLAP

CLAP can utilize natural language supervision when learning audio concepts to overcome the restrictions of the paradigm of one class label to many recordings, focusing on a singular task. It has two encoders to bring audio and text descriptions into a joint multimodal space. Its embeddings are evaluated with a contrastive loss objective to encourage maximum possible distance between audio-language pairs. For this experiment, we only use CLAP's base encoder and leave the use of natural language for future exploration.

### AudioMAE

As an alternative, we utilize AudioMAE [CITE] to retrieve the embeddings of our audio samples. AudioMAE is an extension of image-based Masked Autoencoders (MAE) \[CITE] that employs self-supervised representation learning from audio spectrograms. Its principles are similar to those of the Transformer encoder-decoder design in MAE, where Audio-MAE learns by encoding audio spectrogram patches with a high masking ratio before feeding the non-masked tokens through the encoder. The decoder reorders and decodes the encoded context padded with masked tokens before attempting to reconstruct the input spectrogram. This model minimizes the mean squared error (MSE) on the masked portion of the reconstruction and the input spectrogram to optimize its embeddings. The decoder utilizes local window attention to account for the high correlation among audio spectrograms both locally in time and across nearby frequency bands.

In [4]:
CONFIG_PATH = REPO_DIR / "configs" / "slakh_to_openmic_clap_6_classes.json"
CHECKPOINT_PATH = Path("/home/mg8253/workspace/mir/mir-final-project-instrument-classification/runs/slakh_openmic_overlap_clap/checkpoints/epoch=39-step=3200.ckpt")

SAMPLES_DIR = Path("/home/mg8253/workspace/mir/mir-final-project-instrument-classification/notebook/samples")

TOP_K = 6

print(f"Config     : {CONFIG_PATH}")
print(f"Checkpoint : {CHECKPOINT_PATH}")
print(f"Samples dir: {SAMPLES_DIR}")

Config     : /home/mg8253/workspace/mir/mir-final-project-instrument-classification/configs/slakh_to_openmic_clap_6_classes.json
Checkpoint : /home/mg8253/workspace/mir/mir-final-project-instrument-classification/runs/slakh_openmic_overlap_clap/checkpoints/epoch=39-step=3200.ckpt
Samples dir: /home/mg8253/workspace/mir/mir-final-project-instrument-classification/notebook/samples


In [5]:
model, cfg, device = load_model_bundle(CONFIG_PATH, CHECKPOINT_PATH)
sample_metadata = load_sample_metadata(SAMPLES_DIR)
audio_paths = list_audio_samples(SAMPLES_DIR)

print(f"Loaded model on {device}")
print(f"Labels: {cfg.data.label_names}")
print(f"Found {len(audio_paths)} audio files")
print(f"Metadata available for {len(sample_metadata)} files")

/ext3/miniforge3/envs/mir-inst/lib/python3.10/site-packages/transformers/tokenization_utils_base.py:1601: FutureWarning: `clean_up_tokenization_spaces` was not set. It will be set to `True` by default. This behavior will be depracted in transformers v4.45, and will be then set to `False` by default. For more details check this issue: https://github.com/huggingface/transformers/issues/31884
  warnings.warn(
/ext3/miniforge3/envs/mir-inst/lib/python3.10/site-packages/torch/functional.py:505: UserWarning: torch.meshgrid: in an upcoming release, it will be required to pass the indexing argument. (Triggered internally at /pytorch/aten/src/ATen/native/TensorShape.cpp:4381.)
  return _VF.meshgrid(tensors, **kwargs)  # type: ignore[attr-defined]
Some weights of RobertaModel were not initialized from the model checkpoint at roberta-base and are newly initialized: ['roberta.pooler.dense.bias', 'roberta.pooler.dense.weight']
You should probably TRAIN this model on a down-stream task to be able to

Load the specified checkpoint /scratch/mg8253/.cache/huggingface/hub/models--lukewys--laion_clap/snapshots/b3708341862f581175dba5c356a4ebf74a9b6651/music_audioset_epoch_15_esc_90.14.pt from users.
Load Checkpoint...
logit_scale_a 	 Loaded
logit_scale_t 	 Loaded
audio_branch.spectrogram_extractor.stft.conv_real.weight 	 Loaded
audio_branch.spectrogram_extractor.stft.conv_imag.weight 	 Loaded
audio_branch.logmel_extractor.melW 	 Loaded
audio_branch.bn0.weight 	 Loaded
audio_branch.bn0.bias 	 Loaded
audio_branch.patch_embed.proj.weight 	 Loaded
audio_branch.patch_embed.proj.bias 	 Loaded
audio_branch.patch_embed.norm.weight 	 Loaded
audio_branch.patch_embed.norm.bias 	 Loaded
audio_branch.layers.0.blocks.0.norm1.weight 	 Loaded
audio_branch.layers.0.blocks.0.norm1.bias 	 Loaded
audio_branch.layers.0.blocks.0.attn.relative_position_bias_table 	 Loaded
audio_branch.layers.0.blocks.0.attn.qkv.weight 	 Loaded
audio_branch.layers.0.blocks.0.attn.qkv.bias 	 Loaded
audio_branch.layers.0.blocks.0

In [6]:
all_results = []

for audio_path in audio_paths:
    metadata = sample_metadata.get(audio_path.name, {})
    ground_truth_labels = list(metadata.get("positive_labels", []))
    aggregated_rows = list(metadata.get("all_aggregated_labels", []))

    result = predict_file(audio_path, model, cfg, device)
    rows = build_prediction_table_rows(
        result["predictions"],
        ground_truth_labels=ground_truth_labels,
        threshold=cfg.data.threshold,
    )
    table_df = pd.DataFrame(rows)
    aggregated_df = pd.DataFrame(aggregated_rows)
    if not aggregated_df.empty:
        aggregated_df = aggregated_df.sort_values("relevance", ascending=False)

    display(Markdown(f"## {audio_path.name}"))
    display(Audio(filename=str(audio_path)))

    if not aggregated_df.empty:
        display(Markdown("**OpenMIC aggregated annotations (all instruments)**"))
        display(aggregated_df)
    else:
        display(Markdown("**OpenMIC aggregated annotations:** N/A"))

    display(Markdown(f"**6-class ground truth:** {ground_truth_labels if ground_truth_labels else 'N/A'}"))
    display(Markdown("**Prediction scores**"))
    display(table_df.head(TOP_K))

    all_results.append(
        {
            "audio_path": str(audio_path),
            "ground_truth_labels": ground_truth_labels,
            "aggregated_rows": aggregated_rows,
            "prediction_rows": rows,
        }
    )

## 01_068893_7680.wav

**OpenMIC aggregated annotations (all instruments)**

,instrument,raw_instrument,relevance,positive_at_threshold,in_target_subset
0,synthesizer,synthesizer,1.0,True,True


**6-class ground truth:** ['synthesizer']

**Prediction scores**

...

**OpenMIC aggregated annotations (all instruments)**

,instrument,raw_instrument,relevance,positive_at_threshold,in_target_subset
0,drums,drums,1.0,True,True


**6-class ground truth:** ['drums']

**Prediction scores**

,label,probability,predicted,ground_truth
0,drums,0.992828,True,True
1,guitar,0.532745,True,False
2,violin,0.420888,False,False
3,bass,0.189146,False,False
4,synthesizer,0.126462,False,False
5,piano,0.077476,False,False


## Conclusion

Qualitative results show our model predicts instruments (e.g., piano) that are clearly audible but missing from the ground truth. This is a direct result of the OpenMIC-2018 sparse labeling strategy: to save costs, annotators were only asked to verify an instrument if a preliminary filter (InstrumentDNN) flagged it as highly likely. If the initial filter failed, the instrument was never queried, creating "false negatives" in the ground truth. This suggests our reported scores may be lower than the actual performance, as the model is often "correctly" identifying instruments that the original pipeline simply failed to ask humans about.

We conclude that having a good-performing instrument classifier trained on a synthetic sample generalize to real sounds is not a trivial task. Regardless of problems with the annotations in OpenMIC-2018, the performance of the classifiers trained on synthetic data and evaluated on real data fails to meet state-of-the-art standards, where models typically both train and test on real data. At face value, this suggests that using synthetic samples alone or in combination with real samples as training data may not benefit the performance of an instrument classifier. Nevertheless, this study is limited in scope due to time constraints, and there are many further investigations we can take to explore this research question even further, beyond just redoing the experiment with stronger ground truth labels.